In [1]:
import os
import re
import numpy as np
import pandas as pd
import pretty_midi
import mido
from mido import MidiFile, tick2second, MidiTrack, Message, MetaMessage, second2tick
# import h5py
# import zarr
from sklearn.preprocessing import MinMaxScaler

In [2]:
#File management
#TODO: Plan & Structure & Implement the dataset

class MIDIfiles:

    def __init__(self, midi_dir):
        '''This class imports a list of midi files in a given path.
        But, actually, no need for that. TODO: Just use pathlib from Path'''
        self.midi_dir = midi_dir
    
    def get_paths(self):
        '''This function returns a list of midi files in a given path.'''
        midi_files=[]
        for path, subdirs, files in os.walk(self.midi_dir): 
            for file in files:
                if file.endswith('.mid'):
                    midfile = os.path.join(path, file)
                    midi_files.append(midfile)
        return midi_files

In [4]:
# #Utils

# def midi2arr(midi_file, drum_categories, ticks_per_beat=480, quantize_to=4, norm=True,
#                      min_tempo=240000, max_tempo=1250000, max_numerator=4, max_denominator=4):
    
#     mid = MidiFile(midi_file)
#     ticks_per_quantize = ticks_per_beat // quantize_to
#     total_quantized_time_steps = 32 * (quantize_to // 4)
#     #TODO: Make 32 variable

#     drum_data = []
#     offset_data = []
#     velocity_data = []

#     for track in mid.tracks:
#         time = 0
#         for msg in track:
#             time += msg.time
#             if msg.type == 'note_on' and msg.velocity > 0:
#                 drum_part = next((part for part, pitches in drum_categories.items() if msg.note in pitches), None)
#                 if drum_part:
#                     time_in_quantized_steps = round(time / ticks_per_quantize)
#                     actual_time = time / ticks_per_beat
#                     quantized_time = time_in_quantized_steps * (ticks_per_quantize / ticks_per_beat)
#                     time_offset = actual_time - quantized_time
#                     drum_data.append((time_in_quantized_steps, drum_part))
#                     offset_data.append((time_in_quantized_steps, drum_part, time_offset))
#                     velocity_data.append((time_in_quantized_steps, drum_part, msg.velocity))

#     drum_data.sort(key=lambda x: x[0])

#     hits_matrix = np.zeros((total_quantized_time_steps, len(drum_categories)), dtype=int)
#     offset_matrix = np.zeros((total_quantized_time_steps, len(drum_categories)))
#     velocity_matrix = np.zeros((total_quantized_time_steps, len(drum_categories)))

#     for hit_time, drum_part in drum_data:
#         if 0 <= hit_time < total_quantized_time_steps:
#             part_idx = list(drum_categories.keys()).index(drum_part)
#             hits_matrix[hit_time][part_idx] = 1

#     for hit_time, drum_part, offset in offset_data:
#         if 0 <= hit_time < total_quantized_time_steps:
#             part_idx = list(drum_categories.keys()).index(drum_part)
#             offset_matrix[hit_time][part_idx] = offset

#     for hit_time, drum_part, velocity in velocity_data:
#         if 0 <= hit_time < total_quantized_time_steps:
#             part_idx = list(drum_categories.keys()).index(drum_part)
#             velocity_matrix[hit_time][part_idx] = velocity

#     # Extract metadata
#     numerator = 4
#     denominator = 4
#     tempo = 500000  # Default value for tempo (120 BPM)

#     for track in mid.tracks:
#         for msg in track:
#             if msg.type == 'time_signature':
#                 numerator = msg.numerator
#                 denominator = msg.denominator
#             elif msg.type == 'set_tempo':
#                 tempo = msg.tempo

#     metadata = np.array([numerator, denominator, tempo], dtype=int)

#     # Normalize velocities
#     if norm:
#         scaler = MinMaxScaler(feature_range=(0, 1))
#         velocity_matrix = scaler.fit_transform(velocity_matrix)
#         offset_matrix = np.clip(offset_matrix, -0.5, 0.5)
#     # # Normalize offsets
#     # if norm:
#     #     scaler = MinMaxScaler(feature_range=(-0.5, 0.5))
#     #     offset_matrix = scaler.fit_transform(offset_matrix)


#     # Normalize metadata
#     if norm:
#         metadata = np.array([
#             (numerator - 1) / (max_numerator - 1),
#             (denominator - 1) / (max_denominator - 1),
#             (tempo - min_tempo) / (max_tempo - min_tempo)
#         ], dtype=float)
#     else:
#         metadata = np.array([numerator, denominator, tempo], dtype=int)

#     return hits_matrix, np.round(offset_matrix, decimals=3), np.round(velocity_matrix, decimals=3), np.round(metadata, decimals=3)



# def arr2midi(h_matrix, o_matrix, v_matrix, m_matrix, 
#              drum_categories, save=False, output_file='output.mid', 
#              ticks_per_beat=480, quantize_to=4, quantize_length=1, denorm=True, 
#              min_tempo=240000, max_tempo=1250000, max_numerator=4, max_denominator=4):
    
#     drum_map = [value[0] for value in drum_categories.values()]
#     mid = MidiFile(ticks_per_beat=ticks_per_beat)
#     ticks_per_quantize = ticks_per_beat // quantize_to
#     track = MidiTrack()
#     mid.tracks.append(track)

#     # Denormalize velocities
#     if denorm:
#         scaler = MinMaxScaler(feature_range=(0, 127))
#         v_matrix = scaler.fit_transform(v_matrix).astype(int)
#     # # Denormalize offsets
#     # if denorm: 
#     #     scaler = MinMaxScaler(feature_range=(-0.5, 0.5))
#     #     o_matrix = scaler.fit_transform(o_matrix)

#     # Denormalize metadata
#     if denorm:
#         metadata = {
#             'numerator': int(m_matrix[0] * (max_numerator - 1) + 1),
#             'denominator': int(m_matrix[1] * (max_denominator - 1) + 1),
#             'tempo': int(m_matrix[2] * (max_tempo - min_tempo) + min_tempo)
#         }
#     else:
#         metadata = {
#             'numerator': m_matrix[0],
#             'denominator': m_matrix[1],
#             'tempo': m_matrix[2]
#         }

#     track.append(MetaMessage('time_signature', numerator=metadata['numerator'], denominator=metadata['denominator'], time=0))
#     track.append(MetaMessage('set_tempo', tempo=metadata['tempo'], time=0))

#     previous_time = 0
#     for time_step, row in enumerate(h_matrix):
#         for part, value in enumerate(row):
#             if value == 1:
#                 current_time = time_step * ticks_per_quantize
#                 offset_ticks = int(o_matrix[time_step][part] * ticks_per_beat)
#                 adjusted_time = current_time + offset_ticks
#                 delta_time = adjusted_time - previous_time
#                 track.append(Message('note_on', note=drum_map[part], velocity=int(v_matrix[time_step][part]), time=delta_time))
#                 track.append(Message('note_off', note=drum_map[part], velocity=0, time=quantize_length))
#                 previous_time = adjusted_time

#     if save:
#         mid.save(output_file)
    
#     return mid

In [7]:
DATASET = '/Users/cagrierdem/Desktop/ongoing/POSTDOC/practice/practiceMIDI/2bar_loops_extended' # _extended
print(f"Processed DATASET dir: {DATASET}")

Loops = MIDIfiles(DATASET).get_paths()
Loops.sort()

drum_categories = {
            'Bass Drum 1': [36, 35],
            'Acoustic Snare': [38, 37, 39, 40],
            'Low Floor Tom': [41, 43, 45, 78],
            'Low-Mid Tom': [47, 62, 63, 66, 77],
            'High Tom': [48, 50, 60, 65, 73, 74, 75, 76],
            'Open Hi-Hat': [46],
            'Closed Hi-Hat': [42, 44],
            'Ride Cymbal 1': [51, 53, 56, 59, 67, 68, 69, 70, 71, 72, 80, 81],
            'Crash Cymbal 1': [49, 52, 55, 57]
        }

Processed DATASET dir: /Users/cagrierdem/Desktop/ongoing/POSTDOC/practice/practiceMIDI/2bar_loops_extended


In [10]:
# tempos=[]
# ratios=[]
# meta_error=[]
# for i, loop in enumerate(Loops):
#     try:
#         meta = MidiMatrix(loop).metadf
#         tempo = meta.iloc[2,1]
#         tempos.append(tempo)

#         numerator = test_meta.iloc[0,1]
#         denominator = test_meta.iloc[0,2]
#         ratio = numerator / denominator
#         ratios.append(ratio)
#     except:
#         meta_error.append(loop)

# max_tempo = max(tempos)
# min_tempo = min(tempos)

# min_ratio = min(ratios)
# max_ratio = max(ratios)

# print(f"{max_tempo} is the max and {min_tempo} is the min tempo in the dataset.")
# print(f"{max_ratio} is the max and {min_ratio} is the min ratio in the dataset.")
#1250000 is the max and 240000 is the min tempo in the dataset. --> don't run the loop all the time!

In [24]:
# #TODO: Fix the for-loop to save HDF5. It's blowing up the memory (or cpu?) now

# HDF5_DIR = '/Users/cagrierdem/Desktop/ongoing/POSTDOC/dB_workspace/drumbot/dB_dat/HDF5'

# o_matrices, h_matrices, v_matrices, m_matrices = [], [], [], []
# errors = []

# c=0
# for s, loop in enumerate(Loops):
#     try:
#         midi_matrix = MidiMatrix(loop, subdivision=4)
#         v_matrix = midi_matrix.vel_matrix
#         h_matrix = midi_matrix.hit_matrix
#         o_matrix = midi_matrix.offset_matrix
#         m_matrix = midi_matrix.metadf['value']

#         # v_matrices.append(v_matrix)
#         # h_matrices.append(h_matrix)
#         # o_matrices.append(o_matrix)
#         # m_matrices.append(m_matrix)

#         vpath = os.path.join(HDF5_DIR, 'v_matrices/v_' + str(s) + '.hdf5')
#         hpath = os.path.join(HDF5_DIR, 'h_matrices/h_' + str(s) + '.hdf5')
#         opath = os.path.join(HDF5_DIR, 'o_matrices/o_' + str(s) + '.hdf5')
#         mpath = os.path.join(HDF5_DIR, 'm_matrices/m_' + str(s) + '.hdf5')

#         with h5py.File(vpath, 'w') as f:
#             f.create_dataset('data', data=v_matrix)
#         with h5py.File(hpath, 'w') as f:
#             f.create_dataset('data', data=h_matrix)
#         with h5py.File(opath, 'w') as f:
#             f.create_dataset('data', data=o_matrix)
#         with h5py.File(mpath, 'w') as f:
#             f.create_dataset('data', data=m_matrix)

#         instruments = midi_matrix._GM_instr()
#         c += 1
#         print("{}. Drum parts used in {} are {}".format(s, loop.split('/')[-1].split('.')[0], instruments))

#     except Exception as e:
#         errors.append(loop)
#         print(f"Error in {loop}: {e}")
#         continue

#     # if s >= 49:   #Comment these lines to process all files in the folder.
#     #     break

# print("\n --> {} MIDI files converted and saved with {} errors.".format(c, len(errors)))


In [25]:
# #TODO: Fix the for-loop to save Zarr. It's blowing up the memory (or cpu?) now

# ZARR = '/Users/cagrierdem/Desktop/ongoing/POSTDOC/dB_workspace/drumbot/dB_dat/Zarr'

# # o_matrices, h_matrices, v_matrices, m_matrices = [], [], [], []
# errors = []

# c=0
# for s, loop in enumerate(Loops):
#     try:
#         midi_matrix = MidiMatrix(loop, subdivision=4)
#         v_matrix = midi_matrix.vel_matrix
#         h_matrix = midi_matrix.hit_matrix
#         o_matrix = midi_matrix.offset_matrix
#         m_matrix = midi_matrix.metadf['value']

#         # v_matrices.append(v_matrix)
#         # h_matrices.append(h_matrix)
#         # o_matrices.append(o_matrix)
#         # m_matrices.append(m_matrix)

#         v_dir = os.path.join(ZARR, 'v_matrices')
#         h_dir = os.path.join(ZARR, 'h_matrices')
#         o_dir = os.path.join(ZARR, 'o_matrices')
#         m_dir = os.path.join(ZARR, 'm_matrices')

#         os.makedirs(v_dir, exist_ok=True)
#         os.makedirs(h_dir, exist_ok=True)
#         os.makedirs(o_dir, exist_ok=True)
#         os.makedirs(m_dir, exist_ok=True)

#         zarr.save(os.path.join(v_dir, f"v_{s}.zarr"), v_matrix.to_numpy())
#         zarr.save(os.path.join(h_dir, f"h_{s}.zarr"), h_matrix.to_numpy())
#         zarr.save(os.path.join(o_dir, f"o_{s}.zarr"), o_matrix.to_numpy())
#         zarr.save(os.path.join(m_dir, f"m_{s}.zarr"), m_matrix.to_numpy())

#         instruments = midi_matrix._GM_instr()
#         c += 1
#         print("{}. Drum parts used in {} are {}".format(s, loop.split('/')[-1].split('.')[0], instruments))

#     except Exception as e:
#         errors.append(loop)
#         print(f"Error in {loop}: {e}")
#         continue

#     # if s > 49:   # Comment these lines to process all files in the folder.
#     #     break

# print("\n --> {} MIDI files converted and saved with {} errors.".format(c, len(errors)))


In [9]:
#Utils

def midi2arr(midi_file, drum_categories, ticks_per_beat=480, quantize_to=4, norm=True,
             min_tempo=240000, max_tempo=1250000, max_numerator=4, max_denominator=4, tap2drum=False):
    
    if isinstance(midi_file, str):
        mid = mido.MidiFile(midi_file)
    elif isinstance(midi_file, mido.MidiFile):
        mid = midi_file

    ticks_per_quantize = ticks_per_beat // quantize_to
    total_quantized_time_steps = 32 * (quantize_to // 4)

    drum_data = []
    offset_data = []
    velocity_data = []

    for track in mid.tracks:
        time = 0
        for msg in track:
            time += msg.time
            if msg.type == 'note_on' and msg.velocity > 0:
                drum_part = next((part for part, pitches in drum_categories.items() if msg.note in pitches), None)
                if drum_part:
                    time_in_quantized_steps = round(time / ticks_per_quantize)
                    actual_time = time / ticks_per_beat
                    quantized_time = time_in_quantized_steps * (ticks_per_quantize / ticks_per_beat)
                    time_offset = actual_time - quantized_time
                    drum_data.append((time_in_quantized_steps, drum_part))
                    offset_data.append((time_in_quantized_steps, drum_part, time_offset))
                    velocity_data.append((time_in_quantized_steps, drum_part, msg.velocity))

    drum_data.sort(key=lambda x: x[0])

    if tap2drum:
        array_shape = (total_quantized_time_steps, 1)
    else:
        array_shape = (total_quantized_time_steps, len(drum_categories))

    hits_matrix = np.zeros(array_shape, dtype=int)
    offset_matrix = np.zeros(array_shape)
    velocity_matrix = np.zeros(array_shape)

    for hit_time, drum_part in drum_data:
        if 0 <= hit_time < total_quantized_time_steps:
            if tap2drum:
                part_idx = 0
            else:
                part_idx = list(drum_categories.keys()).index(drum_part)
            hits_matrix[hit_time][part_idx] = 1

    for hit_time, drum_part, offset in offset_data:
        if 0 <= hit_time < total_quantized_time_steps:
            if tap2drum:
                part_idx = 0
            else:
                part_idx = list(drum_categories.keys()).index(drum_part)
            offset_matrix[hit_time][part_idx] = offset

    for hit_time, drum_part, velocity in velocity_data:
        if 0 <= hit_time < total_quantized_time_steps:
            if tap2drum:
                part_idx = 0
            else:
                part_idx = list(drum_categories.keys()).index(drum_part)
            velocity_matrix[hit_time][part_idx] = velocity

    # Extract metadata
    numerator = 4
    denominator = 4
    tempo = 500000  # Default value for tempo (120 BPM)

    for track in mid.tracks:
        for msg in track:
            if msg.type == 'time_signature':
                numerator = msg.numerator
                denominator = msg.denominator
            elif msg.type == 'set_tempo':
                tempo = msg.tempo

    metadata = np.array([numerator, denominator, tempo], dtype=int)

    # Normalize velocities
    if norm:
        scaler = MinMaxScaler(feature_range=(0, 1))
        velocity_matrix = scaler.fit_transform(velocity_matrix)
        offset_matrix = np.clip(offset_matrix, -0.5, 0.5)

    # Normalize metadata
    if norm:
        metadata = np.array([
            (numerator - 1) / (max_numerator - 1),
            (denominator - 1) / (max_denominator - 1),
            (tempo - min_tempo) / (max_tempo - min_tempo)
        ], dtype=float)
    else:
        metadata = np.array([numerator, denominator, tempo], dtype=int)

    return hits_matrix, np.round(offset_matrix, decimals=3), np.round(velocity_matrix, decimals=3), np.round(metadata, decimals=3)



def arr2midi(h_matrix, o_matrix, v_matrix, m_matrix, 
             drum_categories, save=False, output_file='output.mid', 
             ticks_per_beat=480, quantize_to=4, quantize_length=1, denorm=True, 
             min_tempo=240000, max_tempo=1250000, max_numerator=4, max_denominator=4, tap2drum=False):
    
    drum_map = [value[0] for value in drum_categories.values()]
    mid = MidiFile(ticks_per_beat=ticks_per_beat)
    ticks_per_quantize = ticks_per_beat // quantize_to
    track = MidiTrack()
    mid.tracks.append(track)

    if tap2drum:
        drum_map = [38] #hard-code snare drum instead of drum_map[:1] * len(drum_map)

    # Denormalize velocities
    if denorm:
        scaler = MinMaxScaler(feature_range=(0, 127))
        v_matrix = scaler.fit_transform(v_matrix).astype(int)

    # Denormalize metadata
    if denorm:
        metadata = {
            'numerator': int(m_matrix[0] * (max_numerator - 1) + 1),
            'denominator': int(m_matrix[1] * (max_denominator - 1) + 1),
            'tempo': int(m_matrix[2] * (max_tempo - min_tempo) + min_tempo)
        }
    else:
        metadata = {
            'numerator': m_matrix[0],
            'denominator': m_matrix[1],
            'tempo': m_matrix[2]
        }

    track.append(MetaMessage('time_signature', numerator=metadata['numerator'], denominator=metadata['denominator'], time=0))
    track.append(MetaMessage('set_tempo', tempo=metadata['tempo'], time=0))

    previous_time = 0
    for time_step, row in enumerate(h_matrix):
        for part, value in enumerate(row):
            if value == 1:
                current_time = time_step * ticks_per_quantize
                offset_ticks = int(o_matrix[time_step][part] * ticks_per_beat)
                adjusted_time = current_time + offset_ticks
                delta_time = adjusted_time - previous_time
                track.append(Message('note_on', note=drum_map[part], velocity=int(v_matrix[time_step][part]), time=delta_time))
                track.append(Message('note_off', note=drum_map[part], velocity=0, time=quantize_length))
                previous_time = adjusted_time

    if save:
        mid.save(output_file)
    
    return mid

In [4]:
#TODO: This is the new midi2arr version that allows to select specific drum parts when compressing onto the tapping array. 

def midi2arr(midi_file, drum_categories, selected_parts=None, ticks_per_beat=480, quantize_to=4, norm=True,
             min_tempo=240000, max_tempo=1250000, max_numerator=4, max_denominator=4, tap2drum=False):
    
    if isinstance(midi_file, str):
        mid = mido.MidiFile(midi_file)
    elif isinstance(midi_file, mido.MidiFile):
        mid = midi_file

    ticks_per_quantize = ticks_per_beat // quantize_to
    total_quantized_time_steps = 32 * (quantize_to // 4)

    # If tap2drum is True and selected_parts is None, default to the specified parts
    if tap2drum and not selected_parts:
        selected_parts = ['Open Hi-Hat', 'Closed Hi-Hat', 'Ride Cymbal 1'] # Only 'Pulse' layer from the 'Pattern Category'

    drum_data = []
    offset_data = []
    velocity_data = []

    for track in mid.tracks:
        time = 0
        for msg in track:
            time += msg.time
            if msg.type == 'note_on' and msg.velocity > 0:
                drum_part = next((part for part, pitches in drum_categories.items() if msg.note in pitches), None)
                if drum_part and (not tap2drum or drum_part in selected_parts):
                    time_in_quantized_steps = round(time / ticks_per_quantize)
                    actual_time = time / ticks_per_beat
                    quantized_time = time_in_quantized_steps * (ticks_per_quantize / ticks_per_beat)
                    time_offset = actual_time - quantized_time
                    drum_data.append((time_in_quantized_steps, drum_part))
                    offset_data.append((time_in_quantized_steps, drum_part, time_offset))
                    velocity_data.append((time_in_quantized_steps, drum_part, msg.velocity))

    drum_data.sort(key=lambda x: x[0])

    # Set array shape based on tap2drum value
    array_shape = (total_quantized_time_steps, 1 if tap2drum else len(drum_categories))

    hits_matrix = np.zeros(array_shape, dtype=int)
    offset_matrix = np.zeros(array_shape)
    velocity_matrix = np.zeros(array_shape)

    # Fill the matrices
    for hit_time, drum_part in drum_data:
        if 0 <= hit_time < total_quantized_time_steps:
            part_idx = 0 if tap2drum else list(drum_categories.keys()).index(drum_part)
            hits_matrix[hit_time][part_idx] = 1

    for hit_time, drum_part, offset in offset_data:
        if 0 <= hit_time < total_quantized_time_steps:
            part_idx = 0 if tap2drum else list(drum_categories.keys()).index(drum_part)
            offset_matrix[hit_time][part_idx] = offset

    for hit_time, drum_part, velocity in velocity_data:
        if 0 <= hit_time < total_quantized_time_steps:
            part_idx = 0 if tap2drum else list(drum_categories.keys()).index(drum_part)
            velocity_matrix[hit_time][part_idx] = velocity

    # Normalize velocities and offsets
    if norm:
        scaler = MinMaxScaler(feature_range=(0, 1))
        velocity_matrix = scaler.fit_transform(velocity_matrix.reshape(-1, 1)).reshape(array_shape)
        offset_matrix = np.clip(offset_matrix, -0.5, 0.5)

    # Extract and normalize metadata
    numerator = 4
    denominator = 4
    tempo = 500000  # Default value for tempo (120 BPM)

    for track in mid.tracks:
        for msg in track:
            if msg.type == 'time_signature':
                numerator = msg.numerator
                denominator = msg.denominator
            elif msg.type == 'set_tempo':
                tempo = msg.tempo

    metadata = np.array([numerator, denominator, tempo], dtype=int)

    if norm:
        metadata = np.array([
            (numerator - 1) / (max_numerator - 1),
            (denominator - 1) / (max_denominator - 1),
            (tempo - min_tempo) / (max_tempo - min_tempo)
        ], dtype=float)
    else:
        metadata = np.array([numerator, denominator, tempo], dtype=int)

    return hits_matrix, np.round(offset_matrix, decimals=3), np.round(velocity_matrix, decimals=3), np.round(metadata, decimals=3)


In [9]:
NPY = '/Users/cagrierdem/Desktop/ongoing/POSTDOC/dB_workspace/drumbot/dB_dat/npy_tap_pulse_extended'

o_matrices, h_matrices, v_matrices, m_matrices = [],[],[],[]
errors = []

c=0
for s, loop in enumerate(Loops):
    try:
        #NOTE: The selected_parts parameter is checked before including a drum hit in the arrays, ensuring that only the specified drum parts are included when tap2drum is True.
        h_matrix, o_matrix, v_matrix, m_matrix = midi2arr(loop, drum_categories=drum_categories, quantize_to=4, norm=True, tap2drum=True, selected_parts=['Open Hi-Hat', 'Closed Hi-Hat', 'Ride Cymbal 1'])

        v_matrices.append(v_matrix)
        h_matrices.append(h_matrix)
        o_matrices.append(o_matrix)
        m_matrices.append(m_matrix)

        vpath = os.path.join(NPY, 'v_matrices/v_' + str(s) + '.npy')
        hpath = os.path.join(NPY, 'h_matrices/h_' + str(s) + '.npy')
        opath = os.path.join(NPY, 'o_matrices/o_' + str(s) + '.npy')
        mpath = os.path.join(NPY, 'm_matrices/m_' + str(s) + '.npy')
        
        # TODO: Comment and comment out accordingly (you don't need V and O matrices for collapsed tapping arrays)
        # np.save(vpath, v_matrix)
        np.save(hpath, h_matrix)
        # np.save(opath, o_matrix)
        # np.save(mpath, m_matrix)

        c+=1
        print(f"nr.{c} MIDI at {loop} is converted to matrices")
    except Exception as e:
        errors.append(loop)
        print(f"Error in {loop}: {e}")
        continue

    # if s >= 49:   #Comment these lines to process all files in the folder.
    #     break

print("\n --> {} MIDI files converted and saved with {} errors.".format(c, len(errors)))

nr.1 MIDI at /Users/cagrierdem/Desktop/ongoing/POSTDOC/practice/practiceMIDI/2bar_loops_extended/0_0.mid is converted to matrices
nr.2 MIDI at /Users/cagrierdem/Desktop/ongoing/POSTDOC/practice/practiceMIDI/2bar_loops_extended/0_1.mid is converted to matrices
nr.3 MIDI at /Users/cagrierdem/Desktop/ongoing/POSTDOC/practice/practiceMIDI/2bar_loops_extended/0_2.mid is converted to matrices
nr.4 MIDI at /Users/cagrierdem/Desktop/ongoing/POSTDOC/practice/practiceMIDI/2bar_loops_extended/0_3.mid is converted to matrices
nr.5 MIDI at /Users/cagrierdem/Desktop/ongoing/POSTDOC/practice/practiceMIDI/2bar_loops_extended/10000_0.mid is converted to matrices
nr.6 MIDI at /Users/cagrierdem/Desktop/ongoing/POSTDOC/practice/practiceMIDI/2bar_loops_extended/10001_0.mid is converted to matrices
nr.7 MIDI at /Users/cagrierdem/Desktop/ongoing/POSTDOC/practice/practiceMIDI/2bar_loops_extended/10002_0.mid is converted to matrices
nr.8 MIDI at /Users/cagrierdem/Desktop/ongoing/POSTDOC/practice/practiceMIDI/2

In [9]:
longer32=[]
shorter32=[]
for df in v_matrices:
    if df.shape[0] > 32:
        longer32.append(df)
    elif df.shape[0] < 32: 
        shorter32.append(df)
print(f'{len(longer32)} are longer than 32 time steps, and {len(shorter32)} are shorter.')

0 are longer than 32 time steps, and 0 are shorter.


In [11]:
#The current program is not suitable to Type 1 MIDI files.
#TODO: Why? Now it should be ok...
errors[:7]

[]

In [17]:
# pd.set_option('display.max_rows', 500) 
idx = np.random.randint(0, len(Loops))
# idx = 23 #comment thisline out if want random index
TEST_path = Loops[idx]
print("To be tested random MIDI file has index: {} and path: {}".format(idx, TEST_path))
m_matrices[idx]

To be tested random MIDI file has index: 19983 and path: /Users/cagrierdem/Desktop/ongoing/POSTDOC/practice/practiceMIDI/2bar_loops_extended/21045_1.mid


array([1.   , 1.   , 0.158])

In [18]:
# H matrix for hits
H = h_matrices[idx]
#TODO: Why arrays and not dataframe? --> because of padding. Now solved!
H.T

array([[1, 0, 1, 0, 1, 0, 1, 0, 1, 0, 1, 0, 1, 0, 1, 0, 1, 0, 1, 0, 1, 0,
        1, 0, 1, 0, 1, 0, 1, 0, 1, 0]])

In [19]:
# V matrix for velocities
V = v_matrices[idx]
V.T

array([[0.906, 0.   , 0.921, 0.   , 0.921, 0.   , 0.787, 0.   , 0.858,
        0.   , 0.772, 0.   , 0.953, 0.   , 0.843, 0.   , 0.929, 0.   ,
        0.898, 0.   , 0.937, 0.   , 1.   , 0.   , 0.701, 0.   , 0.882,
        0.   , 0.921, 0.   , 0.945, 0.   ]])

In [20]:
# O matrix for offsets
O = o_matrices[idx]
O.T

array([[0.042, 0.   , 0.042, 0.   , 0.054, 0.   , 0.046, 0.   , 0.062,
        0.   , 0.042, 0.   , 0.05 , 0.   , 0.05 , 0.   , 0.037, 0.   ,
        0.042, 0.   , 0.042, 0.   , 0.054, 0.   , 0.042, 0.   , 0.079,
        0.   , 0.058, 0.   , 0.058, 0.   ]])